# 🎙️ Gemini 3.8 TTS: de texto a voz con Python

Este tutorial enseña a convertir un guion **literal** en audio, elegir voces, dirigir la interpretación, crear voces por descripción con distintos acentos y aplicaciones o replicar una voz con consentimiento, controlar estilos y etiquetas, producir un diálogo y recibir audio por streaming.

**Modelos:** `gemini-3.8-flash-tts` (mayor expresividad) y `gemini-3.8-flash-lite-tts` (menor costo y mayor rendimiento). **API:** Interactions, con `google-genai >= 2.25.0`. Cada llamada al servicio puede consumir cuota o generar cargos.

## Ruta de aprendizaje

1. **Empieza aquí:** instala el SDK, prepara la clave y genera tu primer WAV.
2. **Controla el resultado:** explora todas las voces en un DataFrame, prueba voces predefinidas, cambia `style`, añade etiquetas y crea un diálogo.
3. **Elige cómo entregarlo:** compara Flash con Flash-Lite y recibe audio por streaming.
4. **Personaliza la identidad:** diseña voces para casos concretos, replica la tuya con consentimiento y reutiliza su ID.

Ejecuta las celdas en este orden. La creación de voces y las llamadas TTS usan cuota; el bloque de replicación es opcional. Los reproductores que ya aparecen en la notebook provienen de ejecuciones anteriores.

Documentación oficial: [generación de voz](https://ai.google.dev/gemini-api/docs/speech-generation), [diseño de voz](https://ai.google.dev/gemini-api/docs/voice-design), [replicación](https://ai.google.dev/gemini-api/docs/voice-replication) e [Interactions API](https://ai.google.dev/gemini-api/docs/interactions).


## 1. Preparación del entorno

Este tutorial usa la Interactions API y la Voices API mediante `google-genai >= 2.25.0`. Una versión 1.x del SDK envía el esquema antiguo de Interactions y produce `BadRequestError: The legacy Interactions API schema is no longer supported`. Instalamos también `pandas` para explorar el catálogo completo como DataFrame.

Ejecuta la siguiente celda en **este mismo kernel**. Si el SDK se acaba de actualizar, reinicia el kernel y vuelve a ejecutar desde el principio:

```python
%pip install -U "google-genai>=2.25.0" "pandas>=2.2" ipython
```

`%pip` instala en el Python asociado al kernel activo. Desde una terminal, activa el entorno correcto y usa `python -m pip install -r requirements.txt`; después selecciona ese kernel en Jupyter. La celda siguiente muestra el ejecutable y la versión del SDK antes de crear el cliente. La clave se solicita de forma privada si no está en `GEMINI_API_KEY`.


In [1]:
%pip install -U "google-genai>=2.25.0" "pandas>=2.2" ipython

     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 79.5/79.5 kB 528.2 kB/s eta 0:00:00a 0:00:01
  Using cached psutil-7.2.2-cp36-abi3-macosx_11_0_arm64.whl.metadata (22 kB)
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 10.0/10.0 MB 9.9 MB/s eta 0:00:00a 0:00:01
Using cached psutil-7.2.2-cp36-abi3-macosx_11_0_arm64.whl (129 kB)
  Attempting uninstall: psutil
    Found existing installation: psutil 5.9.8
    Uninstalling psutil-5.9.8:
      Successfully uninstalled psutil-5.9.8
  Attempting uninstall: pandas
    Found existing installation: pandas 2.2.2
    Uninstalling pandas-2.2.2:
      Successfully uninstalled pandas-2.2.2
ERROR: pip's dependency resolver does not currently take into account all the packages that are installed. This behaviour is the source of the following dependency conflicts.
promptflow-devkit 1.10.0 requires pandas<3.0.0,>=1.5.3, but you have pandas 3.0.6 which is incompatible.
promptflow-devkit 1.10.0 requires pillow<11.0.0,>=10.1.0, but you have pillow 12.1.0 which is i

In [1]:
import base64
import importlib.metadata as metadata
import json
import os
import re
import sys
import time
import wave
from pathlib import Path
import getpass

try:
    sdk_version = metadata.version("google-genai")
except metadata.PackageNotFoundError as error:
    raise RuntimeError(
        "google-genai no está instalado en este kernel. Ejecuta "
        "en una celda: %pip install -U \"google-genai>=2.25.0\" ipython; "
        "reinicia el kernel y vuelve a empezar."
    ) from error

version_match = re.match(r"^(\d+)\.(\d+)", sdk_version)
if not version_match or tuple(map(int, version_match.groups())) < (2, 25):
    raise RuntimeError(
        f"Este kernel usa google-genai {sdk_version} en {sys.executable}. "
        "Gemini 3.8 TTS requiere >=2.25.0. Ejecuta en una celda "
        "%pip install -U \"google-genai>=2.25.0\" ipython, "
        "reinicia el kernel y vuelve a ejecutar desde el inicio."
    )

print(f"Python del kernel: {sys.executable}")
print(f"google-genai: {sdk_version}")

from IPython.display import Audio, display
from google import genai

# Configura GEMINI_API_KEY en el entorno antes de abrir Jupyter.
# No pegues la clave en la notebook ni la incluyas en archivos compartidos.
if not os.environ.get("GEMINI_API_KEY"):
    os.environ["GEMINI_API_KEY"] = getpass.getpass("Introduce tu GEMINI_API_KEY: ")
    if not os.environ.get("GEMINI_API_KEY"):
        raise RuntimeError("Falta GEMINI_API_KEY. Configúrala en el entorno y vuelve a ejecutar esta celda.")

client = genai.Client()
TTS_TIMEOUT_SECONDS = 90  # Límite de espera de red por solicitud, en segundos.
print("Cliente Gemini listo.")


Python del kernel: /Users/alarcon7a/anaconda3/envs/python3/bin/python
google-genai: 2.25.0
Cliente Gemini listo.


## 2. Cómo funciona una petición TTS

Una llamada a `client.interactions.create()` reúne cuatro piezas:

1. `model`: el motor TTS que genera el audio.
2. `input`: un `user_input` con bloques `text`. El campo `text` contiene las palabras que se pronunciarán. `annotations` añade `speech_metadata` para el estilo y, en diálogos, el hablante.
3. `generation_config.speech_config`: la voz predefinida o el ID de una voz creada. Para dos voces se usa un mapa `speakers`.
4. `response_format={"type": "audio"}`: solicita audio. La respuesta es una `Interaction` con pasos; `interaction.output_audio` da acceso directo al último bloque de audio y su `data` viene en base64.

**Flujo:** guion → metadatos de interpretación + voz → `interactions.create` → audio base64 → bytes → archivo/reproductor. El WAV de una petición normal ya contiene cabecera RIFF; el streaming tiene otra representación que veremos después.

Las `Interaction` se almacenan de forma predeterminada. Para una solicitud sin historial puedes añadir `store=False`; con ello no podrás reutilizar su ID en `previous_interaction_id`. Consulta la [política y retención de Interactions](https://ai.google.dev/gemini-api/docs/interactions#data-storage-and-retention) antes de procesar material sensible.

Para evitar esperas indefinidas, las llamadas de este tutorial usan `timeout=90` segundos. Es un límite de espera de la conexión del SDK; una petición puede tardar más en total si el cliente reintenta errores temporales. Las celdas con varias peticiones muestran qué operación está en curso. Si una voz concreta tarda repetidamente, compara el mismo texto con `Kore` y prueba la voz problemática por separado.

### Función auxiliar para WAV

Esta función sirve para las respuestas normales y las vistas previas de voces diseñadas. Comprueba que hay audio y que el contenido es WAV antes de guardarlo.


In [2]:
def play_and_save(audio_b64_data, filename="output.wav"):
    """Guarda un bloque base64 de audio/wav y muestra su reproductor."""
    if not audio_b64_data:
        raise ValueError("La respuesta no contiene datos de audio.")
    raw_audio = base64.b64decode(audio_b64_data)
    if not raw_audio.startswith(b"RIFF") or raw_audio[8:12] != b"WAVE":
        raise ValueError("Se esperaba audio/wav; revisa response_format y el tipo de respuesta.")
    Path(filename).write_bytes(raw_audio)
    print(f"Guardado: {filename} ({len(raw_audio)} bytes)")
    display(Audio(raw_audio, autoplay=False))


## 3. Primer audio: una voz predefinida

`Kore` identifica una voz predefinida. `speech_metadata.style` describe **cómo** decir el turno completo; el texto se interpreta como transcripción literal. La misma estructura sirve para locuciones de producto, accesibilidad, lectura de artículos o mensajes de una aplicación. Cambia solo el guion y la voz para experimentar.

En la respuesta normal, `output_audio.data` es base64 de un WAV mono de 24 kHz y 16 bits por defecto. Si `output_audio` es `None`, inspecciona el estado y los pasos de la interacción antes de intentar guardar el archivo.


In [3]:
interaction = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
    model="gemini-3.8-flash-tts",
    input=[{
        "type": "user_input",
        "content": [{
            "type": "text",
            "text": "¡Hola! Bienvenidos a este tutorial interactivo sobre Gemini 3.8 Text-to-Speech.",
            "annotations": [{"type": "speech_metadata", "style": "cheerful, warm and clear"}],
        }],
    }],
    response_format={"type": "audio"},
    generation_config={"speech_config": [{"voice": "Kore"}]},
)

if interaction.output_audio is None:
    raise RuntimeError(f"No se recibió audio. Estado: {interaction.status}")
print("Estado:", interaction.status, "| MIME:", interaction.output_audio.mime_type)
play_and_save(interaction.output_audio.data, "01_bienvenida.wav")


Estado: completed | MIME: audio/wav
Guardado: 01_bienvenida.wav (330544 bytes)


## 4. Otra voz predefinida: atención al cliente

Este segundo ejemplo cambia la voz a `Call Center Agent 3` y usa un mensaje de servicio. Escucha la diferencia con el primer audio: seleccionamos otra identidad en `speech_config` y mantenemos el control del tono en `speech_metadata.style`.


In [4]:
interaction = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
    model="gemini-3.8-flash-tts",
    input=[{
        "type": "user_input",
        "content": [{
            "type": "text",
            "text": "Hola, mi nombre es Antonio, y estoy aquí para ayudarte con cualquier consulta que tengas respecto a nuestros servicios.",
            "annotations": [{"type": "speech_metadata", "style": "cheerful, warm and clear"}],
        }],
    }],
    response_format={"type": "audio"},
    generation_config={"speech_config": [{"voice": "Call Center Agent 3"}]},
)

if interaction.output_audio is None:
    raise RuntimeError(f"No se recibió audio. Estado: {interaction.status}")
print("Estado:", interaction.status, "| MIME:", interaction.output_audio.mime_type)
play_and_save(interaction.output_audio.data, "01_call_center_agent_3.wav")


Estado: completed | MIME: audio/wav
Guardado: 01_call_center_agent_3.wav (328624 bytes)


## 5. Explorar la biblioteca de voces

Hasta aquí seleccionamos voces por nombre en `speech_config`. La Voices API permite **descubrir qué voces existen** antes de sintetizar: `client.voices.list()` devuelve metadatos como ID, nombre, idioma, acento, género, tono y descripción. El ID de una voz predefinida se puede usar luego en `speech_config`.

### 5.1 Un filtro pequeño para empezar

La primera consulta pide voces predefinidas de `es-CL`, `es-ES` **o** `es-US` y muestra solo una página. Es útil para aprender la forma de la respuesta, pero **no representa todo el catálogo**. Los valores de un mismo filtro se combinan con OR; filtros distintos, con AND. `search` busca una subcadena en el nombre y la descripción, no hace búsqueda semántica. Si hay `next_page_token`, queda otra página.

Después recorreremos todas las páginas sin `language_code`, de modo que aparezcan voces de otros idiomas y regiones, además de las voces personalizadas guardadas en tu proyecto. [Filtros y paginación oficiales](https://ai.google.dev/gemini-api/docs/speech-generation#extended-voice-library-and-filtering).


In [8]:
print("Consultando una página de voces en español...", flush=True)
spanish_voices = client.voices.list(
    timeout=TTS_TIMEOUT_SECONDS,
    language_code=["es-ES", "es-US"],
    type_=["prebuilt"],
    page_size=50,
)

voices = spanish_voices.voices or []
print(f"Voces encontradas en esta página: {len(voices)}")
for voice in voices:
    print(f"{voice.id} | {voice.display_name} | {voice.language_code} | {voice.gender} | {voice.pitch}")
if spanish_voices.next_page_token:
    print("Hay más resultados; usa page_token para consultar la siguiente página.")


Voces encontradas en esta página: 22
es-es-advisor-2 | Authoritative Advisor 2 | es-ES | male | low
es-es-advisor-8 | Authoritative Advisor 8 | es-ES | neutral | low
es-es-advisor-9 | Authoritative Advisor 9 | es-ES | male | low
es-es-assistant-3 | Digital Assistant 3 | es-ES | male | low
es-es-assistant-4 | Digital Assistant 4 | es-ES | male | low
es-es-commercial-3 | Commercial Voiceover 3 | es-ES | female | medium
es-es-commercial-7 | Commercial Voiceover 7 | es-ES | female | medium
es-es-concierge-12 | Concierge 12 | es-ES | male | low
es-es-concierge-3 | Concierge 3 | es-ES | female | medium
es-es-concierge-4 | Concierge 4 | es-ES | male | low
es-es-csagent-3 | Call Center Agent 3 | es-ES | male | low
es-es-csagent-5 | Call Center Agent 5 | es-ES | female | medium
es-es-csagent-6 | Call Center Agent 6 | es-ES | female | low
es-es-podcaster-5 | Podcaster 5 | es-ES | female | low
es-es-podcaster-7 | Podcaster 7 | es-ES | male | low
es-es-techagent-4 | Tech Advisor 4 | es-ES | male |

### 5.2 Catálogo completo en un DataFrame

Esta consulta **no aplica filtros de idioma ni de tipo**. Usa `page_token` hasta agotar `next_page_token`; cada página puede traer menos filas que `page_size`. La API devuelve las voces personalizadas guardadas en tu proyecto y las voces predefinidas del catálogo. El resultado completo queda en `voices_df`, una fila por ID, con columnas para comparar idioma, región, acento, tipo, género, tono y contexto.

`display(voices_df)` puede abreviar filas en pantalla según la configuración de pandas, pero **el DataFrame conserva todas**. El resumen por idioma sirve para ver qué variedades llegaron. Para examinar una región concreta, por ejemplo `es-CL` o `es-US`, filtra `voices_df` después de descargar el catálogo; no necesitas volver a llamar a la API. Si quieres exportarlo, ejecuta `voices_df.to_csv("gemini_voices_catalog.csv", index=False)`. [Voices API](https://ai.google.dev/api/voices).


In [6]:
import pandas as pd

voice_columns = [
    "id", "display_name", "type", "language_code", "region_code",
    "accent", "gender", "pitch", "persona", "context", "description",
]
voice_rows_by_id = {}
page_token = None
seen_page_tokens = set()
page_number = 0

while True:
    request = {"page_size": 200}
    if page_token:
        request["page_token"] = page_token
    page_number += 1
    print(f"Consultando página {page_number} del catálogo...", flush=True)
    page = client.voices.list(timeout=TTS_TIMEOUT_SECONDS, **request)
    print(f"Página {page_number}: {len(page.voices or [])} voces recibidas.", flush=True)

    for voice in page.voices or []:
        voice_type = getattr(voice.type, "value", voice.type)
        voice_rows_by_id[voice.id] = {
            "id": voice.id,
            "display_name": voice.display_name,
            "type": voice_type,
            "language_code": voice.language_code,
            "region_code": voice.region_code,
            "accent": voice.accent,
            "gender": voice.gender,
            "pitch": getattr(voice.pitch, "value", voice.pitch),
            "persona": voice.persona,
            "context": voice.context,
            "description": voice.description,
        }

    next_page_token = page.next_page_token
    if not next_page_token:
        break
    if next_page_token in seen_page_tokens:
        raise RuntimeError("La API repitió un page_token; se detiene la paginación.")
    seen_page_tokens.add(next_page_token)
    page_token = next_page_token

voices_df = pd.DataFrame.from_records(
    list(voice_rows_by_id.values()), columns=voice_columns
).sort_values(["language_code", "type", "display_name"], na_position="last")
voices_df = voices_df.reset_index(drop=True)

print(f"Voces únicas en el catálogo: {len(voices_df)}")
display(voices_df)

if not voices_df.empty:
    print("Voces por idioma (primeras 20 variedades):")
    display(
        voices_df["language_code"]
        .fillna("Sin código")
        .value_counts()
        .head(20)
        .rename_axis("language_code")
        .reset_index(name="voces")
    )
    # Ejemplo de filtro local, sin otra petición a la API:
    display(voices_df.loc[voices_df["language_code"].isin(["es-CL", "es-ES", "es-US"])] )


Voces únicas en el catálogo: 2098


,id,display_name,type,language_code,region_code,accent,gender,pitch,persona,context,description
0,ar-001-advisor-1,Authoritative Advisor 1,prebuilt,ar-001,001,Modern Standard Arabic,female,medium,High-Trust Advisor / Authoritative Advisor (La...,Enterprise Agent,48-year-old Lawyer from the Arab World. Speaks...
1,ar-001-advisor-10,Authoritative Advisor 10,prebuilt,ar-001,001,Modern Standard Arabic,male,medium,High-Trust Advisor / Authoritative Advisor (La...,Enterprise Agent,50-year-old Lawyer from the Arab World. Speaks...
2,ar-001-advisor-2,Authoritative Advisor 2,prebuilt,ar-001,001,Modern Standard Arabic,male,low,High-Trust Advisor / Authoritative Advisor (La...,Enterprise Agent,43-year-old Lawyer from the Arab World. Speaks...
3,ar-001-advisor-3,Authoritative Advisor 3,prebuilt,ar-001,001,Modern Standard Arabic,male,low,High-Trust Advisor / Authoritative Advisor (La...,Enterprise Agent,36-year-old Lawyer from the Arab World. Speaks...
4,ar-001-csagent-10,Call Center Agent 10,prebuilt,ar-001,001,Modern Standard Arabic,female,high,Customer Support Agent / Call Center Agent (Cu...,Enterprise Agent,25-year-old Customer Service Agent from the Ar...
...,...,...,...,...,...,...,...,...,...,...,...
2093,vi-vn-tutor-8,Tutor 8,prebuilt,vi-VN,VN,Vietnamese,female,high,Educational Tutor (Professor),Conversational / Edu,22-year-old Professor from Vietnam. Speaks Vie...
2094,voice_6pc5solkh0et,The Mad Scientist 1,prompted,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN
2095,voice_ys8hd2y03z8i,The Mad Scientist 2,prompted,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN
2096,voice_wo4u9er4nwhr,The Mad Scientist 3,prompted,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN


Voces por idioma (primeras 20 variedades):


,language_code,voces
0,en-US,215
1,en-IN,120
2,en-GB,117
3,ko-KR,117
4,ja-JP,115
5,hi-IN,114
6,pt-BR,107
7,ar-EG,92
8,de-DE,87
9,es-419,86


,id,display_name,type,language_code,region_code,accent,gender,pitch,persona,context,description
1113,es-es-advisor-2,Authoritative Advisor 2,prebuilt,es-ES,ES,Castilian Spanish,male,low,High-Trust Advisor / Authoritative Advisor (La...,Enterprise Agent,38-year-old Lawyer from Spain. Speaks Castilia...
1114,es-es-advisor-8,Authoritative Advisor 8,prebuilt,es-ES,ES,Castilian Spanish,neutral,low,High-Trust Advisor / Authoritative Advisor (La...,Enterprise Agent,46-year-old Lawyer from Spain. Speaks Castilia...
1115,es-es-advisor-9,Authoritative Advisor 9,prebuilt,es-ES,ES,Castilian Spanish,male,low,High-Trust Advisor / Authoritative Advisor (La...,Enterprise Agent,44-year-old Lawyer from Spain. Speaks Castilia...
1116,es-es-csagent-3,Call Center Agent 3,prebuilt,es-ES,ES,Castilian Spanish,male,low,Customer Support Agent / Call Center Agent (Sa...,Enterprise Agent,32-year-old Sales Associate from Spain. Speaks...
1117,es-es-csagent-5,Call Center Agent 5,prebuilt,es-ES,ES,Castilian Spanish,female,medium,Customer Support Agent / Call Center Agent (Cu...,Enterprise Agent,34-year-old Customer Service Agent from Spain....
1118,es-es-csagent-6,Call Center Agent 6,prebuilt,es-ES,ES,Castilian Spanish,female,low,Customer Support Agent / Call Center Agent (Cu...,Enterprise Agent,56-year-old Customer Service Agent from Spain....
1119,es-es-commercial-3,Commercial Voiceover 3,prebuilt,es-ES,ES,Castilian Spanish,female,medium,Advertising Pitch & Commerce / Commercial Voic...,Growth & Marketing,30-year-old Influencer from Spain. Speaks Cast...
1120,es-es-commercial-7,Commercial Voiceover 7,prebuilt,es-ES,ES,Castilian Spanish,female,medium,Advertising Pitch & Commerce / Commercial Voic...,Growth & Marketing,30-year-old Influencer from Spain. Speaks Cast...
1121,es-es-concierge-12,Concierge 12,prebuilt,es-ES,ES,Castilian Spanish,male,low,Concierge & EA (Tour Guide),Enterprise Agent,27-year-old Tour Guide from Spain. Speaks Cast...
1122,es-es-concierge-3,Concierge 3,prebuilt,es-ES,ES,Castilian Spanish,female,medium,Concierge & EA (Executive Assistant),Enterprise Agent,24-year-old Executive Assistant from Spain. Sp...


## 6. Dirigir la interpretación con `style`

El texto de Gemini 3.8 TTS es una **transcripción literal**. Para dirigir la interpretación, separa las instrucciones por alcance:

| Control | Dónde se escribe | Para qué sirve | Ejemplos |
|---|---|---|---|
| Identidad vocal persistente | Voz predefinida o `voices.create(prompted=...)` | Timbre, acento y carácter estable | Guía chilena o instructora española |
| Interpretación de todo el turno | `annotations: [{"type": "speech_metadata", "style": "..."}]` | Emoción, velocidad, volumen, entonación | `"natural, casual and friendly"`, `"whispered urgently"`, `"calm and reassuring"`, `"speaking rapidly"` |
| Evento en un instante | Etiqueta `<...>` dentro de `text` | Pausa o sonido vocal justo donde aparece | `<short pause>`, `<laugh>`, `<sigh>` |

`style` acepta una descripción breve en lenguaje natural, no una lista cerrada de valores. Por ejemplo, `"natural, casual and friendly"` pide una entrega cercana durante todo ese bloque de texto; `"whispered urgently"` pide un susurro urgente. Para cambiar de emoción a mitad de un diálogo, divide el guion en turnos y asigna un `style` a cada uno. Para mantener una voz estable, evita repetir una biografía larga en `style`: sus rasgos permanentes pertenecen a Voice Design. [Guía oficial de prompting](https://ai.google.dev/gemini-api/docs/speech-generation#prompting-guide).

**Prueba controlada:** la siguiente celda pronuncia un recordatorio de cita tres veces con la misma voz `Puck`; solo cambia `style`. Escucha qué cambia en la entrega y qué se mantiene en la identidad vocal.


In [9]:
frase_comparacion = (
    "Tu cita es mañana a las diez. Si necesitas cambiarla, avísanos hoy."
)
estilos = {
    "cercano": "natural, casual and friendly",
    "tranquilizador": "calm, reassuring and unhurried",
    "breve": "upbeat, clear and concise",
}

for nombre, estilo in estilos.items():
    print(f"Generando estilo {nombre}...", flush=True)
    resultado = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
        model="gemini-3.8-flash-tts",
        input=[{
            "type": "user_input",
            "content": [{
                "type": "text",
                "text": frase_comparacion,
                "annotations": [{"type": "speech_metadata", "style": estilo}],
            }],
        }],
        response_format={"type": "audio"},
        generation_config={"speech_config": [{"voice": "Puck"}]},
    )
    if resultado.output_audio is None:
        raise RuntimeError(f"No se recibió audio para {nombre}. Estado: {resultado.status}")
    print(f"Estilo: {estilo}")
    play_and_save(resultado.output_audio.data, f"11_estilo_{nombre}.wav")


Estilo: natural, casual and friendly
Guardado: 11_estilo_cercano.wav (213424 bytes)


Estilo: calm, reassuring and unhurried
Guardado: 11_estilo_tranquilizador.wav (276784 bytes)


Estilo: upbeat, clear and concise
Guardado: 11_estilo_breve.wav (215344 bytes)


### 6.1 Añadir pausas y sonidos vocales

Las etiquetas en inglés marcan **eventos puntuales**. La grafía importa: para risa usa `<laugh>` o `<laughter>`; **`<laught>` no es una etiqueta documentada**. En un texto en español, conserva las etiquetas en inglés. Estas señales guían la generación; no fijan una duración exacta ni garantizan que todas se interpreten igual en cada ejecución.

| Etiqueta | Intención | Ejemplo de fragmento |
|---|---|---|
| `<short pause>` / `<long pause>` | Pausa breve / larga | `Abre la puerta... <short pause> y observa` |
| `<laugh>` / `<chuckle>` | Risa / risita | `No puedo creerlo <laugh>` |
| `<sigh>` / `<breath>` | Suspiro / respiración | `<breath> Respira con calma` |
| `<gasp>` | Inhalación de sorpresa | `<gasp> ¡Hay una luz en el sótano!` |
| `<cough>` / `<throat-clearing>` | Tos / aclarar la garganta | `<cough> Disculpen` |
| `<cheer>` / `<shout>` | Exclamación vocal | `<cheer> ¡Salió del horno!` |

Comas, puntos suspensivos y mayúsculas también influyen en ritmo y énfasis. Usa etiquetas para sonidos **humanos**; efectos como aplausos o golpes deben añadirse en edición de audio. [Lista oficial de etiquetas](https://ai.google.dev/gemini-api/docs/speech-generation#vocal-bursts-and-non-speech-sounds).

**Prueba:** una escena de misterio y un consejo de cocina muestran varias etiquetas en contexto. El `style` marca el tono general de cada escena; las etiquetas señalan momentos específicos.


In [18]:
escenas_etiquetas = [
    (
        "misterio",
        "<breath> La puerta del ático estaba entreabierta. <short pause> "
        "Escuché un ruido detrás de mí... <gasp> ¡Alguien había entrado! "
        "<long pause> Entonces encontré una nota sobre la mesa.",
        "quiet, tense audiobook narration",
    ),
    (
        "cocina",
        "<breath> Saca el pan del horno con cuidado. <short pause> "
        "¡Quedó perfecto! <chuckle> Aunque casi olvido la sal. <sigh> "
        "Déjalo enfriar antes de cortarlo.",
        "warm, conversational cooking instructor",
    ),
]

for nombre, guion, estilo in escenas_etiquetas:
    print(f"Generando escena {nombre}...", flush=True)
    resultado = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
        model="gemini-3.8-flash-tts",
        input=[{
            "type": "user_input",
            "content": [{
                "type": "text",
                "text": guion,
                "annotations": [{"type": "speech_metadata", "style": estilo}],
            }],
        }],
        response_format={"type": "audio"},
        generation_config={"speech_config": [{"voice": "Puck"}]},
    )
    if resultado.output_audio is None:
        raise RuntimeError(f"No se recibió audio para {nombre}. Estado: {resultado.status}")
    print(f"Escena: {nombre} | style: {estilo} | texto: {guion}")
    play_and_save(resultado.output_audio.data, f"12_etiquetas_{nombre}.wav")


Escena: misterio | style: quiet, tense audiobook narration | texto: <breath> La puerta del ático estaba entreabierta. <short pause> Escuché un ruido detrás de mí... <gasp> ¡Alguien había entrado! <long pause> Entonces encontré una nota sobre la mesa.
Guardado: 12_etiquetas_misterio.wav (595504 bytes)


Escena: cocina | style: warm, conversational cooking instructor | texto: <breath> Saca el pan del horno con cuidado. <short pause> ¡Quedó perfecto! <chuckle> Aunque casi olvido la sal. <sigh> Déjalo enfriar antes de cortarlo.
Guardado: 12_etiquetas_cocina.wav (491824 bytes)


## 7. Crear un diálogo con dos hablantes

En una llamada puedes asignar **hasta dos voces predefinidas** a `speech_config.speakers`. Cada bloque de texto marca su `speaker` con el mismo nombre configurado y puede tener su propio `style`. `mode="conversational"` favorece la alternancia natural.

**Límite clave:** una voz `voice_...` o `voicekey_...` personalizada no se puede combinar dentro de este modo de dos hablantes. Para un podcast con tu voz replicada, genera cada turno por separado y une los fragmentos PCM del mismo formato; no concatenes archivos WAV completos por sus cabeceras. El siguiente ejemplo usa `Puck` y `Kore`.


In [18]:
dialogo_podcast = [
    {
        "type": "text",
        "text": "Bienvenida al programa. ¿Qué podemos crear con Gemini TTS?",
        "annotations": [{"type": "speech_metadata", "speaker": "Host", "style": "curious and welcoming"}],
    },
    {
        "type": "text",
        "text": "Narraciones, lecturas accesibles y diálogos. <short pause> También podemos dirigir el tono de cada turno.",
        "annotations": [{"type": "speech_metadata", "speaker": "Guest", "style": "clear and enthusiastic"}],
    },
    {
        "type": "text",
        "text": "¿Y si quiero una identidad vocal propia?",
        "annotations": [{"type": "speech_metadata", "speaker": "Host", "style": "interested"}],
    },
    {
        "type": "text",
        "text": "Puedes diseñarla con una descripción o replicar tu voz con la grabación de consentimiento.",
        "annotations": [{"type": "speech_metadata", "speaker": "Guest", "style": "calm and informative"}],
    },
]

interaction_podcast = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
    model="gemini-3.8-flash-tts",
    input=[{"type": "user_input", "content": dialogo_podcast}],
    response_format={"type": "audio"},
    generation_config={
        "speech_config": {
            "mode": "conversational",
            "speakers": [
                {"speaker": "Host", "voice": "Puck"},
                {"speaker": "Guest", "voice": "Kore"},
            ],
        }
    },
)

if interaction_podcast.output_audio is None:
    raise RuntimeError(f"No se recibió audio. Estado: {interaction_podcast.status}")
play_and_save(interaction_podcast.output_audio.data, "05_podcast_dos_voces.wav")


Guardado: 05_podcast_dos_voces.wav (948784 bytes)


## 8. Elegir entre Flash TTS y Flash-Lite TTS

| Necesidad | Elección inicial | Por qué |
|---|---|---|
| Audiolibro, doblaje o actuación con matices | `gemini-3.8-flash-tts` | Prioriza fidelidad, control expresivo y estabilidad de voz |
| Lectura de artículos, notificaciones o síntesis a gran escala | `gemini-3.8-flash-lite-tts` | Prioriza velocidad y eficiencia de costo |
| Un asistente que debe responder con audio progresivo | `gemini-3.8-flash-lite-tts` + streaming | Permite consumir fragmentos conforme llegan |

Ambos modelos aceptan texto y producen audio. Si necesitas conversación bidireccional en tiempo real con entrada de micrófono, consulta [Gemini Live API](https://ai.google.dev/gemini-api/docs/live), que cubre un flujo distinto. Compara las mismas frases, voz y estilo antes de elegir para tu producto. La tabla expresa criterios de selección, no una promesa de latencia o calidad para toda petición. [Cuándo usar cada modelo](https://ai.google.dev/gemini-api/docs/speech-generation#when-to-use-which-model).


In [10]:
interaction_lite = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
    model="gemini-3.8-flash-lite-tts",
    input=[{
        "type": "user_input",
        "content": [{
            "type": "text",
            "text": "Esta línea fue sintetizada con Gemini 3.8 Flash-Lite TTS. Diseñada para alto rendimiento y bajo costo.",
            "annotations": [{
                "type": "speech_metadata",
                "style": "clear, direct and concise",
            }],
        }],
    }],
    response_format={"type": "audio"},
    generation_config={"speech_config": [{"voice": "Zephyr"}]},
)

play_and_save(interaction_lite.output_audio.data, "07_flash_lite_demo.wav")


Guardado: 07_flash_lite_demo.wav (384304 bytes)


## 9. Formatos de audio y streaming

| Modo o formato | Qué recibes | Uso típico |
|---|---|---|
| Petición normal: `audio/wav` | Archivo completo con cabecera RIFF, PCM mono 16 bits a 24 kHz por defecto | Guardar, escuchar, editar |
| Streaming: `audio/l16` | Fragmentos PCM **sin cabecera**, mono 16 bits a 24 kHz por defecto | Reproducción progresiva o transporte propio |
| `audio/mulaw` / `audio/alaw` | Audio G.711 de 8 bits | Sistemas de telefonía compatibles |

Para elegir un formato usa, por ejemplo, `response_format={"type": "audio", "mime_type": "audio/l16", "sample_rate": 24000}`. El reproductor debe conocer el formato y la frecuencia de muestreo. Con `stream=True`, procesa los eventos `step.delta` de tipo `audio` a medida que llegan; guardar todos los fragmentos para escucharlos al final es una demostración del protocolo, no una reproducción de baja latencia. El primer fragmento puede tardar mientras el servidor prepara la voz. La celda muestra el tipo de evento recibido y el estado final, sin imprimir el audio codificado; si no hay fragmentos, ese diagnóstico ayuda a distinguir una respuesta vacía de un problema de formato. [Referencia de streaming y formatos](https://ai.google.dev/gemini-api/docs/speech-generation#streaming-speech-generation).


In [4]:
print("Iniciando streaming TTS...", flush=True)
stream_started = time.monotonic()
stream = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
    model="gemini-3.8-flash-tts",
    input=[{
        "type": "user_input",
        "content": [{
            "type": "text",
            "text": "Este audio llega en fragmentos PCM mientras el modelo lo genera.",
            "annotations": [{"type": "speech_metadata", "style": "clear and upbeat"}],
        }],
    }],
    response_format={"type": "audio", "mime_type": "audio/l16", "sample_rate": 24000},
    generation_config={"speech_config": [{"voice": "Kore"}]},
    stream=True,
)

pcm_chunks = []
event_counts = {}
final_status = None
final_error = None
for event in stream:
    kind = event.event_type
    event_counts[kind] = event_counts.get(kind, 0) + 1
    if kind == "step.delta" and getattr(event.delta, "type", None) == "audio":
        chunk = base64.b64decode(event.delta.data)
        if chunk:
            pcm_chunks.append(chunk)
            print(f"Fragmento {len(pcm_chunks)}: {len(chunk)} bytes", flush=True)
    elif kind in ("interaction.status_update", "interaction.completed"):
        interaction_event = getattr(event, "interaction", None)
        if interaction_event is not None:
            final_status = getattr(interaction_event, "status", final_status)
            final_error = getattr(interaction_event, "error", final_error)
            print(f"Evento: {kind} | estado: {final_status}", flush=True)
    elif kind != "step.delta":
        print(f"Evento: {kind}", flush=True)

pcm_audio = b"".join(pcm_chunks)
print(f"Streaming finalizado en {time.monotonic() - stream_started:.1f} s. Eventos: {event_counts}")
if not pcm_audio:
    raise RuntimeError(
        f"El streaming terminó sin audio. Estado: {final_status}; "
        f"error: {final_error}; eventos: {event_counts}. "
        "Prueba la petición normal de la sección 3 para aislar el streaming."
    )

# El streaming es PCM L16 mono a 24 kHz: añadir cabecera WAV.
with wave.open("06_streaming_demo.wav", "wb") as wav_file:
    wav_file.setnchannels(1)
    wav_file.setsampwidth(2)
    wav_file.setframerate(24000)
    wav_file.writeframes(pcm_audio)

print(f"Guardado: 06_streaming_demo.wav ({len(pcm_audio)} bytes PCM)")
display(Audio(filename="06_streaming_demo.wav"))


Iniciando streaming TTS...
Evento: interaction.created
Evento: step.start
Fragmento 1: 1920 bytes
Fragmento 2: 1920 bytes
Fragmento 3: 1920 bytes
Fragmento 4: 5760 bytes
Fragmento 5: 1920 bytes
Fragmento 6: 3840 bytes
Fragmento 7: 3840 bytes
Fragmento 8: 5760 bytes
Fragmento 9: 1920 bytes
Fragmento 10: 1920 bytes
Fragmento 11: 3840 bytes
Fragmento 12: 3840 bytes
Fragmento 13: 1920 bytes
Fragmento 14: 1920 bytes
Fragmento 15: 1920 bytes
Fragmento 16: 1920 bytes
Fragmento 17: 3840 bytes
Fragmento 18: 1920 bytes
Fragmento 19: 3840 bytes
Fragmento 20: 3840 bytes
Fragmento 21: 1920 bytes
Fragmento 22: 5760 bytes
Fragmento 23: 5760 bytes
Fragmento 24: 1920 bytes
Fragmento 25: 1920 bytes
Fragmento 26: 1920 bytes
Fragmento 27: 1920 bytes
Fragmento 28: 3840 bytes
Fragmento 29: 1920 bytes
Fragmento 30: 1920 bytes
Fragmento 31: 5760 bytes
Fragmento 32: 1920 bytes
Fragmento 33: 1920 bytes
Fragmento 34: 3840 bytes
Fragmento 35: 1920 bytes
Fragmento 36: 3840 bytes
Fragmento 37: 5760 bytes
Fragmento 

## 10. Diseñar una voz propia con texto

`client.voices.create(type="prompted")` convierte una descripción breve de rasgos permanentes —acento, timbre, edad aparente y personalidad vocal— en un ID `voice_...` reutilizable. Devuelve además `sample_audio` en WAV para escuchar una vista previa. Es útil para una voz de marca, un narrador de audiolibro o un personaje recurrente.

La creación es opcional y ocupa un cupo de voces personalizadas (máximo 200 por proyecto entre diseñadas y replicadas, con vigencia de un año). La celda usa `CREATE_DESIGNED_VOICE=True`: al repetirla se crea otra voz y se consume cuota. La creación puede tardar más que una síntesis porque primero genera y guarda la identidad. Cambia la bandera a `False` y asigna un ID existente a `designed_voice_id` si deseas reutilizarlo. Si ya tienes un ID diseñado, puedes asignarlo directamente a `designed_voice_id`. No pongas emociones pasajeras en la descripción permanente: van en `speech_metadata.style`.


In [ ]:
CREATE_DESIGNED_VOICE = False  # Cambia a True para crear una voz nueva en tu proyecto.
designed_voice_id = None  # O pega aquí un voice_... que ya hayas creado. --- voice_6xx5h0bl9ezn

if CREATE_DESIGNED_VOICE:
    print("Creando una nueva voz diseñada...", flush=True)
    designed_voice = client.voices.create(
        timeout=TTS_TIMEOUT_SECONDS,
        store=True,
        voice={
            "model": "gemini-3.8-flash-tts",
            "type": "prompted",
            "display_name": "Narrador épico",
            "gender": "male",
            "language_code": "es-ES",
            "prompted": {
                "input": "Narrador maduro de documentales, voz grave y profunda, ritmo pausado y tono reflexivo."
            },
        },
    )
    designed_voice_id = designed_voice.id
    print("ID de voz diseñada:", designed_voice_id)
    if designed_voice.sample_audio and designed_voice.sample_audio.data:
        play_and_save(designed_voice.sample_audio.data, "02_voz_diseniada_preview.wav")
else:
    print("Diseño de voz omitido. Activa CREATE_DESIGNED_VOICE para probarlo.")


ID de voz diseñada: voice_6xx5h0bl9ezn
Guardado: 02_voz_diseniada_preview.wav (818224 bytes)


### 10.1 ¿Puede una voz predefinida ser la base?

**La API actual no documenta un campo `base_voice` para derivar una voz nueva de `Puck`, `Kore` u otra voz predefinida.** `voices.create()` permite diseñar una identidad desde una descripción (`type="prompted"`) o replicar una voz con audio y consentimiento (`type="replicated"`). Puedes seleccionar una voz predefinida y cambiar la interpretación de cada turno mediante `style`, pero eso no crea una nueva identidad vocal. [Referencia de Voices API](https://ai.google.dev/api/voices).

| Necesidad | Solución | Ejemplo práctico |
|---|---|---|
| Prototipo inmediato | Seleccionar `Puck` y ajustar `style` | Audio de bienvenida a un museo |
| Identidad vocal reutilizable | Crear una voz `prompted` y guardar su `voice_...` | Guía chilena de museo o instructora de cocina española |

Primero generamos una bienvenida con `Puck`. En la siguiente sección usaremos una guía chilena diseñada que leerá **la misma frase**, para comparar una voz predefinida con una diseñada sin cambiar el guion.


In [5]:
museum_welcome = (
    "Bienvenidos al museo de ciencias. <short pause> "
    "Nuestro viaje comienza con el cielo nocturno y las historias detrás de sus estrellas."
)

In [6]:

museum_prebuilt = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
    model="gemini-3.8-flash-lite-tts",
    input=[{
        "type": "user_input",
        "content": [{
            "type": "text",
            "text": museum_welcome,
            "annotations": [{
                "type": "speech_metadata",
                "style": "clear, warm and welcoming museum guide",
            }],
        }],
    }],
    response_format={"type": "audio"},
    generation_config={"speech_config": [{"voice": "Puck"}]},
)
if museum_prebuilt.output_audio is None:
    raise RuntimeError(f"No se recibió audio. Estado: {museum_prebuilt.status}")
play_and_save(museum_prebuilt.output_audio.data, "08_museum_prebuilt.wav")


Guardado: 08_museum_prebuilt.wav (418864 bytes)


### 10.2 Diseñar voces para aplicaciones diferentes

Vamos a diseñar dos identidades, cada una con su acento y función:

1. **Guía chilena de museo**: voz serena y curiosa para una audioguía en español. Repite la frase que escuchaste con `Puck` para que puedas comparar.
2. **Instructora de cocina, español de España (`es-ES`)**: voz cercana y clara para un tutorial de receta. Su texto y su `style` son distintos porque el contexto también cambia.

`language_code` identifica el idioma declarado y `region_code` indica la región. Para la guía chilena usamos `language_code="es-CL"` y `region_code="CL"`. La clave de caché de este ejemplo es `museum_es_cl`: si ejecutaste una versión anterior con otra clave, ese ID no se reutiliza y se creará una voz chilena nueva al ejecutar la celda. La voz anterior permanece en tu proyecto hasta que la gestiones por separado. El acento, timbre y carácter que deben persistir se describen en `prompted.input`. `speech_metadata.style` solo dirige **la actuación de una toma**. Escucha las vistas previas y las salidas: la descripción orienta al modelo, pero el acento concreto se evalúa por oído. [Voice Design](https://ai.google.dev/gemini-api/docs/voice-design) y [campos de la Voices API](https://ai.google.dev/api/voices).

La celda muestra el progreso de cada creación y cada síntesis. Si una voz tarda, el mensaje indica cuál se está procesando. La celda guarda ambos IDs en `custom_voice_examples.json`. Si la ejecutas de nuevo, reutiliza las voces en lugar de crear duplicados. Cada creación consume cuota y cuenta para el límite de voces personalizadas del proyecto.


In [8]:
custom_voice_file = Path("custom_voice_examples.json")
custom_voice_ids = (
    json.loads(custom_voice_file.read_text(encoding="utf-8"))
    if custom_voice_file.is_file() else {}
)

voice_examples = [
    {
        "key": "museum_es_cl",
        "display_name": "Guía chilena de museo",
        "gender": "female",
        "language_code": "es-CL",
        "region_code": "CL",
        "prompt": (
            "Guía adulta de museo chilena con acento suave de Chile, voz clara "
            "y reflexiva, y un sentido de curiosidad tranquila. Dicción natural "
            "adecuada para exposiciones científicas y guías de audio."
        ),
        "text": museum_welcome,
        "style": "warm, curious and unhurried",
        "filename": "10_museum_es_cl.wav",
    },
    {
        "key": "cooking_es_es",
        "display_name": "Instructora de cocina española",
        "gender": "female",
        "language_code": "es-ES",
        "region_code": "ES",
        "prompt": (
            "Voz adulta de instructora de cocina con acento de España, "
            "timbre cálido, dicción nítida y ritmo fácil de seguir. "
            "Personalidad práctica y cercana para explicar recetas paso a paso."
        ),
        "text": (
            "Precalienta el horno a ciento ochenta grados. <short pause> "
            "Después mezcla la harina con el aceite de oliva hasta obtener "
            "una masa uniforme."
        ),
        "style": "clear, patient and encouraging",
        "filename": "10_cooking_es_es.wav",
    },
]

for example in voice_examples:
    key = example["key"]
    voice_id = custom_voice_ids.get(key)
    if not voice_id:
        print(f"Creando voz para {key}...", flush=True)
        created_voice = client.voices.create(
        timeout=TTS_TIMEOUT_SECONDS,
            store=True,
            voice={
                "model": "gemini-3.8-flash-tts",
                "type": "prompted",
                "display_name": example["display_name"],
                "gender": example["gender"],
                "language_code": example["language_code"],
                "region_code": example["region_code"],
                "prompted": {"input": example["prompt"]},
            },
        )
        voice_id = created_voice.id
        custom_voice_ids[key] = voice_id
        custom_voice_file.write_text(
            json.dumps(custom_voice_ids, ensure_ascii=False, indent=2),
            encoding="utf-8",
        )
        print(f"Voz creada para {key}: {voice_id}")
        if created_voice.sample_audio and created_voice.sample_audio.data:
            play_and_save(created_voice.sample_audio.data, f"09_{key}_preview.wav")
    else:
        print(f"Reutilizando voz para {key}: {voice_id}")

    print(f"Sintetizando ejemplo de {key}...", flush=True)
    result = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
        model="gemini-3.8-flash-tts",
        input=[{
            "type": "user_input",
            "content": [{
                "type": "text",
                "text": example["text"],
                "annotations": [{
                    "type": "speech_metadata",
                    "style": example["style"],
                }],
            }],
        }],
        response_format={"type": "audio"},
        generation_config={"speech_config": [{"voice": voice_id}]},
    )
    if result.output_audio is None:
        raise RuntimeError(f"No se recibió audio para {key}. Estado: {result.status}")
    play_and_save(result.output_audio.data, example["filename"])


Creando voz para museum_es_cl...
Voz creada para museum_es_cl: voice_clkujh5p7kgt
Guardado: 09_museum_es_cl_preview.wav (2404144 bytes)


Sintetizando ejemplo de museum_es_cl...
Guardado: 10_museum_es_cl.wav (453424 bytes)


Creando voz para cooking_es_es...
Voz creada para cooking_es_es: voice_npoqcatuaxyc
Guardado: 09_cooking_es_es_preview.wav (2889904 bytes)


Sintetizando ejemplo de cooking_es_es...
Guardado: 10_cooking_es_es.wav (476464 bytes)


## 11. Replicar tu voz con consentimiento

La API requiere **dos grabaciones de la misma persona adulta**: `me.wav`, con 10–30 segundos de voz natural, y `consent.wav`, con la declaración obligatoria pronunciada exactamente. Para mejores resultados graba ambos con el mismo micrófono y entorno, en WAV PCM mono de 16 bits a 24 kHz. El clip de referencia debe tener voz clara, sin música ni voces superpuestas.

Declaración admitida en español (`es-ES` y `es-US`): **«Soy el propietario de esta voz y doy mi consentimiento para que Google la utilice para crear un modelo de voz sintética.»** Hay otros idiomas y frases exactas en la [guía de replicación](https://ai.google.dev/gemini-api/docs/voice-replication#supported-consent-phrases-by-language).

Con `store=True`, la API devuelve un `voice_...` guardado en el proyecto durante un año. Con `store=False`, devuelve `replicated_voice.key` (`voicekey_...`), que debes guardar tú y caduca a los siete días. En el ejemplo se usa el modo guardado. Trata el ID y las grabaciones como datos privados. La celda solo envía los archivos cuando activas explícitamente `CREATE_REPLICATED_VOICE`. Si existe `my_voice_info.json`, recupera el ID para un posible uso posterior, pero **no lo selecciona automáticamente** para generar audio.


In [ ]:
def b64_file(filepath):
    return base64.b64encode(Path(filepath).read_bytes()).decode("ascii")

CREATE_REPLICATED_VOICE = False  # Activa solo si eres la persona que consintió.
me_path = Path("me.wav")
consent_path = Path("consent.wav")
voice_info_path = Path("my_voice_info.json")
my_voice_id = None

if CREATE_REPLICATED_VOICE:
    if not (me_path.is_file() and consent_path.is_file()):
        raise FileNotFoundError("Faltan me.wav o consent.wav; créalos primero con record_clips.py.")
    replicated_voice = client.voices.create(
        timeout=TTS_TIMEOUT_SECONDS,
        store=True,
        voice={
            "model": "gemini-3.8-flash-tts",
            "type": "replicated",
            "display_name": "alarcon",
            "replicated": {
                "source_audio": {"mime_type": "audio/wav", "data": b64_file(me_path)},
                "consent_audio": {"mime_type": "audio/wav", "data": b64_file(consent_path)},
            },
        },
    )
    my_voice_id = replicated_voice.id
    voice_info_path.write_text(json.dumps({"voice_id": my_voice_id}, indent=2), encoding="utf-8")
    print("Voz replicada creada. ID guardado localmente en", voice_info_path)
elif voice_info_path.is_file():
    my_voice_id = json.loads(voice_info_path.read_text(encoding="utf-8")).get("voice_id")
    print("ID de voz replicada disponible en", voice_info_path, "(uso opcional)")
else:
    print("Replicación omitida. Puedes grabar los clips con: python3 record_clips.py")


Voz replicada creada. ID guardado localmente en my_voice_info.json


## 12. Usar una voz personalizada para sintetizar

Una voz guardada se selecciona con su ID en `generation_config.speech_config`. Para una voz replicada no hay que reenviar los audios en cada síntesis. Por defecto, la celda usa la voz diseñada y, si no creaste ninguna, `Kore`. La voz replicada se selecciona solo al cambiar `USE_REPLICATED_VOICE=True`. Esto permite probarla por separado si su generación tarda más en tu proyecto.

El texto de prueba no promete una copia perfecta: escucha el resultado y evalúa pronunciación, ritmo y consistencia. Si elegiste `store=False`, usa la **clave** `replicated_voice.key`, no `.id`, en el campo `voice`.


In [17]:
USE_REPLICATED_VOICE = True  # Activa para probar explícitamente tu voz replicada.
if USE_REPLICATED_VOICE and not my_voice_id:
    raise ValueError("No hay ID de voz replicada. Ejecuta la sección 11 primero.")
target_voice = my_voice_id if USE_REPLICATED_VOICE else (designed_voice_id or "Kore")
print("Voz seleccionada:", target_voice, flush=True)
print("Sintetizando prueba corta...", flush=True)

interaction_custom = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
    model="gemini-3.8-flash-tts",
    input=[{
        "type": "user_input",
        "content": [{
            "type": "text",
            "text": "Esta es una prueba de síntesis de voz con Gemini 3.8. <short pause> Escucha el timbre, el ritmo y la dicción de mi voz",
            "annotations": [{"type": "speech_metadata", "style": "natural, casual and friendly"}],
        }],
    }],
    response_format={"type": "audio"},
    generation_config={"speech_config": [{"voice": target_voice}]},
)

if interaction_custom.output_audio is None:
    raise RuntimeError(f"No se recibió audio. Estado: {interaction_custom.status}")
play_and_save(interaction_custom.output_audio.data, "03_prueba_voz.wav")


Voz seleccionada: voice_c2kwl4a51rbg
Sintetizando prueba corta...
Guardado: 03_prueba_voz.wav (445744 bytes)


In [19]:
USE_REPLICATED_VOICE = True  # Activa para probar explícitamente tu voz replicada.
if USE_REPLICATED_VOICE and not my_voice_id:
    raise ValueError("No hay ID de voz replicada. Ejecuta la sección 11 primero.")
target_voice = my_voice_id if USE_REPLICATED_VOICE else (designed_voice_id or "Kore")
print("Voz seleccionada:", target_voice, flush=True)
print("Sintetizando prueba corta...", flush=True)

interaction_custom = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
    model="gemini-3.8-flash-tts",
    input=[{
        "type": "user_input",
        "content": [{
            "type": "text",
            "text": "Hoy vamos a descubrir cómo funciona Gemini tres punto ocho "
                    "para sintetizar voz y ponerlo a prueba. <short pause> "
                    "Así que ponte cómodo, suscríbete ... ¡y vamos a empezar!",
            "annotations": [{"type": "speech_metadata", "style": "natural, casual and friendly; clear, curious and upbeat"}],
        }],
    }],
    response_format={"type": "audio"},
    generation_config={"speech_config": [{"voice": target_voice}]},
)

if interaction_custom.output_audio is None:
    raise RuntimeError(f"No se recibió audio. Estado: {interaction_custom.status}")
play_and_save(interaction_custom.output_audio.data, "03_prueba_voz_2.wav")


Voz seleccionada: voice_c2kwl4a51rbg
Sintetizando prueba corta...
Guardado: 03_prueba_voz_2.wav (478384 bytes)


In [11]:
texto_actuado = (
    "No vas a creer lo que pasó... <long pause> "
    "¡El servidor resistió todo el tráfico! <laugh> "
    "Pensé que colapsaríamos en el minuto uno <sigh>, pero fue un éxito absoluto."
)

print(f"Sintetizando actuación con {target_voice}...", flush=True)
interaction_acting = client.interactions.create(
    timeout=TTS_TIMEOUT_SECONDS,
    model="gemini-3.8-flash-tts",
    input=[{
        "type": "user_input",
        "content": [{
            "type": "text",
            "text": texto_actuado,
            "annotations": [{
                "type": "speech_metadata",
                "style": "excited, relieved, slightly emotional"
            }],
        }],
    }],
    response_format={"type": "audio"},
    generation_config={"speech_config": [{"voice": target_voice}]},
)

if interaction_acting.output_audio is None:
    raise RuntimeError(f"No se recibió audio. Estado: {interaction_acting.status}")
play_and_save(interaction_acting.output_audio.data, "04_actuacion_director.wav")


Sintetizando actuación con voice_c2kwl4a51rbg...
Guardado: 04_actuacion_director.wav (674224 bytes)


## 13. Resumen y próximos pasos

1. Escribe el **guion pronunciable** en `text`; coloca la emoción sostenida en `speech_metadata.style` (`"natural, casual and friendly"`, por ejemplo) y los eventos puntuales en etiquetas como `<short pause>` o `<laugh>`.
2. Explora el catálogo completo en `voices_df`, filtra localmente por idioma o acento y elige una voz predefinida o crea un `voice_...` para una identidad estable. No existe un parámetro documentado para derivar una voz diseñada de una predefinida; compara ambas rutas en el ejemplo de la audioguía. Guarda el ID si vas a reutilizarlo. Las voces personalizadas guardadas tienen un límite de 200 por proyecto y una vigencia de un año; las claves `voicekey_...` duran siete días.
3. Para dos hablantes en una sola petición usa voces **predefinidas** y marca `speaker` en cada turno. Para usar voces personalizadas con varios personajes, sintetiza los turnos por separado.
4. Una petición normal devuelve WAV completo; streaming devuelve PCM sin cabecera por defecto. No guardes PCM crudo con extensión `.wav` sin crear la cabecera.
5. Revisa el audio generado antes de publicarlo: pronunciación, pausas, duración y consistencia pueden variar. La replicación requiere la grabación de consentimiento del propietario adulto de la voz.

**Si una celda parece detenida:** mira el último mensaje de progreso y prueba el mismo guion con `Kore`. Si solo falla una voz personalizada, verifica su ID y vuelve a intentar con un texto corto; el estado de una respuesta sin audio y los eventos de streaming se muestran en las celdas correspondientes. `timeout` limita la espera de la conexión, pero los reintentos automáticos del SDK pueden alargar el tiempo total.

**Próximo experimento:** toma el mismo párrafo, genera una versión con cada modelo y compara escucha, tamaño de archivo y tiempo medido en tu entorno. La API está en evolución; usa las [guías oficiales de TTS](https://ai.google.dev/gemini-api/docs/speech-generation) y [voz](https://ai.google.dev/gemini-api/docs/voice-replication) para verificar cambios.
